In [18]:
import pandas as pd
import numpy as np
import plotly.express as px

# importerer hele datasettet
trips_df_full = pd.read_csv("../raw_data/trips.csv")

# importerer stations og gjør samme prosedyre som i 01_explore_stations for at treningsdata
# i trips.csv skal være samme periode som stations.csv tross at data går over ulike perioder
stations_df_full = pd.read_csv("../raw_data/stations.csv")
stations_df_full["timestamp"] = pd.to_datetime(stations_df_full["timestamp"], utc=True).dt.tz_convert("Europe/Oslo")
stations_df_full = stations_df_full.sort_values(by="timestamp", ascending=True)

split_index = int(0.7*len(stations_df_full))
train_start = stations_df_full["timestamp"].min() 
train_end = stations_df_full.iloc[split_index]["timestamp"]

# konverterer til riktig format og tidssone for å sortere trips_df kronologisk
# PS - vil endre dtype på timestamp til Europe/Oslo
trips_df_full["started_at"] = pd.to_datetime(trips_df_full["started_at"],utc=True, format="ISO8601").dt.tz_convert("Europe/Oslo")
trips_df_full["ended_at"] = pd.to_datetime(trips_df_full["ended_at"],utc=True, format="ISO8601").dt.tz_convert("Europe/Oslo")
trips_df_full = trips_df_full.sort_values(by="started_at", ascending=True)

# bruker kun treningsdata-perioden fra stations.csv i analyse av trips.csv
trips_df = trips_df_full[(trips_df_full["started_at"] >= train_start) & (trips_df_full["ended_at"] <= train_end)]

In [19]:
# første 5 radene (i treningsdata)
head = trips_df.head()
head

,started_at,ended_at,start_station_name,start_station_latitude,start_station_longitude,end_station_name,end_station_latitude,end_station_longitude
550626,2024-04-11 05:28:38.527000+02:00,2024-04-11 05:32:40.747000+02:00,Torgallmenningen,60.392966,5.323538,C. Sundts gate,60.399475,5.308762
550627,2024-04-11 05:35:16.111000+02:00,2024-04-11 05:40:15.226000+02:00,Gågaten,60.395070,5.318798,Lysverket,60.389626,5.329864
550628,2024-04-11 06:12:34.641000+02:00,2024-04-11 06:33:40.227000+02:00,Sandviksbodene,60.405695,5.323374,Moxy Hotellet,60.378783,5.333327
550629,2024-04-11 06:14:10.220000+02:00,2024-04-11 06:21:21.434000+02:00,Festplassen,60.391124,5.325714,C. Sundts gate,60.399475,5.308762
550630,2024-04-11 06:23:08.461000+02:00,2024-04-11 06:25:08.598000+02:00,Thormøhlens gate,60.383162,5.324053,Florida Bybanestopp,60.382255,5.332332


In [20]:
# siste 5 radene (i treningsdata)
tail = trips_df.tail()
tail

,started_at,ended_at,start_station_name,start_station_latitude,start_station_longitude,end_station_name,end_station_latitude,end_station_longitude
889947,2025-02-17 17:43:02.997000+01:00,2025-02-17 17:54:42.640000+01:00,Lars Hilles,60.388118,5.331487,C. Sundts gate,60.399475,5.308762
889948,2025-02-17 17:46:42.517000+01:00,2025-02-17 18:02:15.291000+01:00,Nonneseterplass,60.389672,5.333605,Solheimsgaten (ved Extra),60.375141,5.338517
889949,2025-02-17 17:46:53.005000+01:00,2025-02-17 17:55:13.283000+01:00,Allehelgens plass,60.392651,5.328977,Moxy Hotellet,60.378783,5.333327
889950,2025-02-17 17:49:51.978000+01:00,2025-02-17 17:55:34.155000+01:00,Nedre Korskirkeallmenning,60.394550,5.327050,Nykirkekaien,60.397057,5.314548
889951,2025-02-17 17:52:41.457000+01:00,2025-02-17 18:03:51.429000+01:00,Nygårdsporten,60.383934,5.333450,Den Nationale Scene,60.392455,5.320185


In [21]:
# data info
info = trips_df.info()
info

<class 'pandas.core.frame.DataFrame'>
Index: 339326 entries, 550626 to 889951
Data columns (total 8 columns):
 #   Column                   Non-Null Count   Dtype                      
---  ------                   --------------   -----                      
 0   started_at               339326 non-null  datetime64[ns, Europe/Oslo]
 1   ended_at                 339326 non-null  datetime64[ns, Europe/Oslo]
 2   start_station_name       339326 non-null  object                     
 3   start_station_latitude   339326 non-null  float64                    
 4   start_station_longitude  339326 non-null  float64                    
 5   end_station_name         339326 non-null  object                     
 6   end_station_latitude     339326 non-null  float64                    
 7   end_station_longitude    339326 non-null  float64                    
dtypes: datetime64[ns, Europe/Oslo](2), float64(4), object(2)
memory usage: 23.3+ MB


In [22]:
# data beskrivelse
description = trips_df.describe(include='all')
description

,started_at,ended_at,start_station_name,start_station_latitude,start_station_longitude,end_station_name,end_station_latitude,end_station_longitude
count,339326,339326,339326,339326.000000,339326.000000,339326,339326.000000,339326.000000
unique,NaN,NaN,127,NaN,NaN,127,NaN,NaN
top,NaN,NaN,Møllendalsplass,NaN,NaN,Torgallmenningen,NaN,NaN
freq,NaN,NaN,9937,NaN,NaN,10719,NaN,NaN
mean,2024-08-12 01:50:51.317473792+02:00,2024-08-12 02:01:29.369597184+02:00,NaN,60.387948,5.327234,NaN,60.388296,5.326788
min,2024-04-11 05:28:38.527000+02:00,2024-04-11 05:32:40.747000+02:00,NaN,60.341031,5.273174,NaN,60.341031,5.273174
25%,2024-05-31 05:48:22.572250112+02:00,2024-05-31 05:54:03.131749888+02:00,NaN,60.381512,5.320002,NaN,60.381750,5.320185
50%,2024-08-09 08:19:18.043999744+02:00,2024-08-09 08:25:35.772499968+02:00,NaN,60.388910,5.325714,NaN,60.389626,5.325714
75%,2024-10-08 18:43:05.607749888+02:00,2024-10-08 18:52:54.744750080+02:00,NaN,60.394550,5.333327,NaN,60.394550,5.332873
max,2025-02-17 17:52:41.457000+01:00,2025-02-17 18:03:51.429000+01:00,NaN,60.423343,5.361202,NaN,60.423343,5.361202


In [23]:
# hvor lenge målingene har holdt på (i treningsdata)
min = trips_df["started_at"].min()
max = trips_df["ended_at"].max()

print("Målinger startet", min, "og sluttet", max)

Målinger startet 2024-04-11 05:28:38.527000+02:00 og sluttet 2025-02-17 18:03:51.429000+01:00


In [24]:
# sjekk for manglende verdier (i treningsdata)
isna = trips_df.isna().sum()
isna

started_at                 0
ended_at                   0
start_station_name         0
start_station_latitude     0
start_station_longitude    0
end_station_name           0
end_station_latitude       0
end_station_longitude      0
dtype: int64

In [25]:
# sjekk for unike rader (i treningsdata)
nunique = trips_df.nunique()
nunique

started_at                 339319
ended_at                   339307
start_station_name            127
start_station_latitude        131
start_station_longitude       131
end_station_name              127
end_station_latitude          130
end_station_longitude         130
dtype: int64

In [26]:
# sjekker om antall turer (i treningsdata) er konsistent
value_count = trips_df["start_station_name"].value_counts()
value_count_check = trips_df["end_station_name"].value_counts()

if (len(value_count) == len(value_count_check)):
    print("Antall start- og slutturer er konsistent")

Antall start- og slutturer er konsistent


In [27]:
# sjekker etter outliers / unormalt lange turer (i treningsdata)
long_trips = trips_df[((trips_df["ended_at"] - trips_df["started_at"]).dt.total_seconds() / 60)> 24*60]

if (len(long_trips) == 0):
    print("Ingen outliers / unormalt lange turer i data")

Ingen outliers / unormalt lange turer i data


In [28]:
# finner korteste og lengste tur (i treningsdata)
shortest_trip = ((trips_df["ended_at"] - trips_df["started_at"]).dt.total_seconds() / 360).min()
longest_trip = ((trips_df["ended_at"] - trips_df["started_at"]).dt.total_seconds() / 360).max()

print("Korteste tur var", round(shortest_trip, 2), "h, og lengste tur var",
       round(longest_trip), "h")

Korteste tur var 0.17 h, og lengste tur var 121 h


In [29]:
# visualiserer antall turer per dag via lineplot
trips_per_day = trips_df.groupby(trips_df["started_at"].dt.date).size()

fig = px.line(trips_per_day)
fig.update_layout(title="antall turer per dag", xaxis_title="timestamp", yaxis_title="antall turer")
fig.show()

In [30]:
# visualiserer varighet av turer via histogram
trips_df["duration_min"] = (trips_df["ended_at"] - trips_df["started_at"]).dt.total_seconds() / 60

fig = px.histogram(trips_df["duration_min"], nbins=10000, range_x=(0,80))
fig.update_layout(title="varighet av turer", xaxis_title="minutter", yaxis_title="antall turer")
fig.show()

C:\Users\Jon\AppData\Local\Temp\ipykernel_6784\3986369056.py:2: SettingWithCopyWarning:


A value is trying to be set on a copy of a slice from a DataFrame.
Try using .loc[row_indexer,col_indexer] = value instead

See the caveats in the documentation: https://pandas.pydata.org/pandas-docs/stable/user_guide/indexing.html#returning-a-view-versus-a-copy



In [31]:
# visualiserer turvarighet per time på døgnet via boxplot
trips_df["hour"] = trips_df["started_at"].dt.hour
fig = px.box(trips_df, "hour", "duration_min")
fig.update_layout(title="turvarighet per time på døgnet", xaxis_title="time på døgnet",
                  yaxis_title="lengde på tur i min")
fig.show()

C:\Users\Jon\AppData\Local\Temp\ipykernel_6784\3278437871.py:2: SettingWithCopyWarning:


A value is trying to be set on a copy of a slice from a DataFrame.
Try using .loc[row_indexer,col_indexer] = value instead

See the caveats in the documentation: https://pandas.pydata.org/pandas-docs/stable/user_guide/indexing.html#returning-a-view-versus-a-copy



In [32]:
# visualiserer total mengde turer per ukedag via histogram
trips_df["day_of_week"] = trips_df["started_at"].dt.day_name()
fig = px.histogram(trips_df, "day_of_week")
fig.update_layout(title="total mengde turer per ukedag", xaxis_title="dag i uka",
                  yaxis_title="antall turer")
fig.show()

C:\Users\Jon\AppData\Local\Temp\ipykernel_6784\3482024974.py:2: SettingWithCopyWarning:


A value is trying to be set on a copy of a slice from a DataFrame.
Try using .loc[row_indexer,col_indexer] = value instead

See the caveats in the documentation: https://pandas.pydata.org/pandas-docs/stable/user_guide/indexing.html#returning-a-view-versus-a-copy

